## 337 - Temperature Gradients on Real Weather Grids Part 1

[Youtube](https://www.youtube.com/watch?v=SxS2rNn_i_A)

In [1]:
from datetime import datetime

import numpy as np
import matplotlib.pyplot as plt

import cartopy.crs as ccrs
import cartopy.feature as cfeature

from herbie import Herbie

import metpy.calc as mpcalc
from metpy.units import units
from metpy.plots import USCOUNTIES

In [2]:
valid_time = datetime(2023, 4, 20, 12)

H = Herbie(valid_time, model='hrrr', product='prs', fxx=0)

ds = H.xarray(':TMP:850 mb')
ds

✅ Found ┊ model=hrrr ┊ product=prs ┊ 2023-Apr-20 12:00 UTC F00 ┊ GRIB2 @ aws ┊ IDX @ local


<xarray.Dataset> Size: 38MB
Dimensions:              (y: 1059, x: 1799)
Coordinates:
    latitude             (y, x) float64 15MB 21.14 21.15 21.15 ... 47.85 47.84
    longitude            (y, x) float64 15MB 237.3 237.3 237.3 ... 299.0 299.1
    time                 datetime64[ns] 8B 2023-04-20T12:00:00
    step                 timedelta64[ns] 8B 00:00:00
    isobaricInhPa        float64 8B 850.0
    valid_time           datetime64[ns] 8B 2023-04-20T12:00:00
    gribfile_projection  object 8B None
Dimensions without coordinates: y, x
Data variables:
    t                    (y, x) float32 8MB 289.8 289.8 289.8 ... 269.8 269.9
Attributes:
    GRIB_edition:            2
    GRIB_centre:             kwbc
    GRIB_centreDescription:  US National Weather Service - NCEP
    GRIB_subCentre:          0
    Conventions:             CF-1.7
    institution:             US National Weather Service - NCEP
    model:                   hrrr
    product:                 prs
    description:             High-Resolution Rapid Refresh - CONUS
    remote_grib:             https://noaa-hrrr-bdp-pds.s3.amazonaws.com/hrrr....
    local_grib:              C:\Users\jessi\data\hrrr\20230420\subset_cfef440...
    search:                  :TMP:850 mb

In [3]:
temperature = ds['t']
lat = ds['latitude']
lon = ds['longitude']

In [4]:
west = -104
east = -92
south = 31
north = 40

In [5]:
temperature = temperature.metpy.quantify()

In [6]:
dx, dy = mpcalc.lat_lon_grid_deltas(lon, lat)

In [7]:
print(f'temperature shape: {temperature.shape}')
print(f'dx: {dx.shape}')
print(f'dy: {dy.shape}')

temperature shape: (1059, 1799)
dx: (1059, 1798)
dy: (1058, 1799)


In [8]:
dTdy, dTdx = mpcalc.gradient(temperature, deltas=(dy, dx))
temperature_gradient = (dTdx**2 + dTdy**2) ** 0.5

In [9]:
temperature_gradient

Magnitude,[[7.244417918960238e-17 2.8609792490763984e-17 1.0877446920284917e-05 ... 1.3877787807814457e-17 4.85722573273506e-17 5.594315114139762e-17] [6.283435673255384e-17 9.813077866773595e-18 6.938893903907228e-18 ... 0.0 6.938893903907228e-18 0.0] [1.0874592807484651e-05 1.0874221605262913e-05 1.0873850930168127e-05 ... 1.0874672882237035e-05 6.938893903907228e-18 2.7755575615628914e-17] ... [2.1124384058643364e-05 2.1125051725946753e-05 1.0562062060882893e-05 ... 2.9876606183739127e-05 1.4938630490628547e-05 2.361833667593537e-05] [2.3619860172744995e-05 1.4938467255895605e-05 1.0563323204017261e-05 ... 1.4938630490616492e-05 2.3620719085216604e-05 1.493839522494495e-05] [2.9878901121819454e-05 2.3621382893787785e-05 1.0564123216282029e-05 ... 1.4939671980269779e-05 2.3622206609560083e-05 3.340612938875885e-05]]
Units,kelvin/meter


In [10]:
temperature_gradient_100km = temperature_gradient * (100 * units.kilometer)

In [11]:
temperature_gradient_100km = temperature_gradient_100km.to('kelvin')

In [12]:
temperature_gradient_100km

Magnitude,[[7.244417918960238e-12 2.8609792490763985e-12 1.0877446920284917 ... 1.3877787807814457e-12 4.85722573273506e-12 5.594315114139762e-12] [6.283435673255384e-12 9.813077866773595e-13 6.938893903907228e-13 ... 0.0 6.938893903907228e-13 0.0] [1.087459280748465 1.0874221605262913 1.0873850930168127 ... 1.0874672882237035 6.938893903907228e-13 2.7755575615628914e-12] ... [2.1124384058643364 2.112505172594675 1.0562062060882893 ... 2.9876606183739125 1.4938630490628546 2.361833667593537] [2.3619860172744995 1.4938467255895604 1.056332320401726 ... 1.4938630490616494 2.3620719085216604 1.493839522494495] [2.9878901121819457 2.3621382893787786 1.0564123216282029 ... 1.493967198026978 2.3622206609560084 3.3406129388758847]]
Units,kelvin


In [13]:
print(np.nanmin(temperature_gradient_100km), np.nanmax(temperature_gradient_100km))

0.0 kelvin 45.18198672815304 kelvin
